In [1]:
import ROOT as root
import math, os
from pathlib import Path

# ============================================================
# EDIT ONLY THIS CELL IN NORMAL USE
# ============================================================

INPUT_FILE = "input/sigma_cascade_prod_qa_pidveto_angle_pp_79513_79516_surv_seg.root"
OUTDIR = Path("output/sigma_xi_omega_QA")
DATASET = "p+p 2025"

# Cuts to compare / draw for each particle.
SELECTED_CUTS = {
    "sigma": ["cut01_loose", "cut03_baseline", "cut05", "cut08"],
    "xi":    ["cut02_loose", "cut03_baseline", "cut05", "cut08"],
    "omega": ["cut02_loose", "cut03_baseline", "cut05", "cut09_tight"],
}


# Display names for the four selected cuts, in SELECTED_CUTS order.
CUT_DISPLAY_NAMES = ["Loose", "Baseline", "Tight", "Tightest"]

# Common requirements shown in the selection pad.
COMMON_SELECTIONS = [
    "No PID requirement",
    "No crossing = 0 requirement",
    "All daughter tracks use the same crossing",
]

# Arbitrary mother-pT intervals used for the 1D mass spectra.
PT_BINS = {
    "sigma": [(0.5,1.0), (1.0,1.5), (1.5,2.0), (2.0,3.0), (3.0,5.0)],
    "xi":    [(0.5,1.0), (1.0,1.5), (1.5,2.0), (2.0,3.0), (3.0,5.0)],
    "omega": [(0.5,1.0), (1.0,1.5), (1.5,2.0), (2.0,3.0), (3.0,5.0)],
}

# None = original topological histograms.
# Or choose "all", "loose", "normal", "tight" to use the PID-category histograms.
# For pT spectra the notebook then projects the stored TH3 over the requested pT interval.
MASS_PID_CATEGORY = None

# PID/angular QA folder to display.
PID_QA_CATEGORY = "all"       # "all", "loose", "normal", "tight"
PLOT_TOPOLOGY_QA = True
PLOT_PID_QA = True

# Plot / output controls.
MASS_REBIN = {"sigma":2, "xi":2, "omega":2}
QA_REBIN_X = 1
QA_REBIN_Y = 1
QA_LOGZ = True
QA_MIN_CONTENT = 1.0
NORMALIZE_CUT_COMPARISON = False
N_COLS = 3

SAVE_PDF = True
SAVE_PNG = False
OUTDIR.mkdir(parents=True, exist_ok=True)

root.gErrorIgnoreLevel = root.kWarning
root.gStyle.SetOptStat(0)
root.gStyle.SetOptFit(0)
root.gStyle.SetPalette(root.kBird)
root.gStyle.SetNumberContours(100)
root.gStyle.SetTitleFont(42, "")
root.gStyle.SetLabelFont(42, "XYZ")
root.gStyle.SetTitleFont(42, "XYZ")
%jsroot on


Welcome to JupyROOT 6.30/06


# \(\Sigma(1385)\), \(\Xi\), and \(\Omega\) mass + QA

The notebook reads the histogram ROOT file produced by `MakeSigmaCascadeHistograms`.
The first cell controls the input file, selected cut folders, \(p_T\) intervals, PID category, and output options.

The topological QA histograms stored by the macro are 2D `variable × mass`, so they are shown for each selected cut integrated over the \(p_T\) accepted by that cut. The 1D mass spectra can be projected into arbitrary \(p_T\) intervals. When `MASS_PID_CATEGORY` is not `None`, the pT spectra are projected from the stored PID TH3.


In [2]:
# ============================================================
# Histogram map and common helpers
# ============================================================

KEEP = []
def keep(obj):
    KEEP.append(obj)
    root.SetOwnership(obj, False)
    return obj

species = {
    "sigma": {
        "top":"sigma1385", "pid_prefix":"sigma",
        "label":"#Sigma(1385) #rightarrow #Lambda#pi",
        "mass_title":"m_{#Lambda#pi} [GeV/c^{2}]",
        "mass_1d":"h_mass_sigma1385", "mass_vs_pt":"h_mass_vs_pt",
        "qa":[
            ("h_mass_vs_lambda_mass",       "m_{#Lambda} [GeV/c^{2}]"),
            ("h_mass_vs_lambda_decayR",     "R_{#Lambda} [cm]"),
            ("h_mass_vs_lambda_pairDCA",    "DCA_{p#pi} [cm]"),
            ("h_mass_vs_lambda_DIRA",       "DIRA_{#Lambda}"),
            ("h_mass_vs_bachelor_pt",       "p_{T}^{#pi} [GeV/c]"),
            ("h_mass_vs_bachelor_dcaXY",    "|DCA_{xy}^{#pi}| [cm]"),
            ("h_mass_vs_pt",                "p_{T}^{#Sigma} [GeV/c]"),
        ],
    },
    "xi": {
        "top":"cascade", "pid_prefix":"xi",
        "label":"#Xi #rightarrow #Lambda#pi",
        "mass_title":"m_{#Lambda#pi} [GeV/c^{2}]",
        "mass_1d":"h_mass_xi", "mass_vs_pt":"h_xi_mass_vs_pt",
        "qa":[
            ("h_xi_mass_vs_lambdaMass",     "m_{#Lambda} [GeV/c^{2}]"),
            ("h_xi_mass_vs_lambdaFlight",   "L_{#Lambda}^{cascade} [cm]"),
            ("h_xi_mass_vs_DIRA",           "DIRA_{cascade}"),
            ("h_xi_mass_vs_decayR",         "R_{cascade} [cm]"),
            ("h_xi_mass_vs_bachelorDCAxy",  "|DCA_{xy}^{bach}| [cm]"),
            ("h_xi_mass_vs_cascadeDCA",     "DCA_{#Lambda,bach} [cm]"),
            ("h_xi_mass_vs_lambdaDIRA",     "DIRA_{#Lambda}^{cascade}"),
            ("h_xi_mass_vs_pt",             "p_{T}^{#Xi} [GeV/c]"),
        ],
    },
    "omega": {
        "top":"cascade", "pid_prefix":"omega",
        "label":"#Omega #rightarrow #Lambda K",
        "mass_title":"m_{#Lambda K} [GeV/c^{2}]",
        "mass_1d":"h_mass_omega", "mass_vs_pt":"h_omega_mass_vs_pt",
        "qa":[
            ("h_omega_mass_vs_lambdaMass",    "m_{#Lambda} [GeV/c^{2}]"),
            ("h_omega_mass_vs_lambdaFlight",  "L_{#Lambda}^{cascade} [cm]"),
            ("h_omega_mass_vs_DIRA",          "DIRA_{cascade}"),
            ("h_omega_mass_vs_decayR",        "R_{cascade} [cm]"),
            ("h_omega_mass_vs_bachelorDCAxy", "|DCA_{xy}^{bach}| [cm]"),
            ("h_omega_mass_vs_cascadeDCA",    "DCA_{#Lambda,bach} [cm]"),
            ("h_omega_mass_vs_lambdaDIRA",    "DIRA_{#Lambda}^{cascade}"),
            ("h_omega_mass_vs_pt",            "p_{T}^{#Omega} [GeV/c]"),
        ],
    },
}

pid_qa = [
    ("h_mass_vs_signed_lambda_bachelor_dphi", "signed #Delta#phi_{#Lambda,bach} [rad]"),
    ("h_mass_vs_lambda_bachelor_opening",     "3D opening angle [rad]"),
    ("h_mass_vs_abs_lambda_bachelor_deta",    "|#Delta#eta_{#Lambda,bach}|"),
    ("h_mass_vs_abs_dphi_over_abs_deta",      "|#Delta#phi|/(|#Delta#eta|+10^{-3})"),
    ("h_mass_vs_bachelor_p",                  "p_{bach} [GeV/c]"),
    ("h_nsigma_target_vs_bachelor_p",         "p_{bach} [GeV/c]"),
    ("h_min_abs_other_nsigma_vs_bachelor_p",  "p_{bach} [GeV/c]"),
    ("h_nsigma_target_vs_min_abs_other",       "min |N#sigma_{other}|"),
    ("h_lnDedx_vs_bachelor_p",                "p_{bach} [GeV/c]"),
]

f = root.TFile.Open(INPUT_FILE, "READ")
if not f or f.IsZombie():
    raise OSError(f"Cannot open ROOT file: {INPUT_FILE}")

_counter = 0
def unique(name):
    global _counter
    _counter += 1
    return f"{name}_{_counter}"

def get_hist(path, required=True):
    obj = f.Get(path)
    if not obj:
        if required: raise KeyError(f"Missing ROOT object: {path}")
        return None
    h = obj.Clone(unique(obj.GetName()))
    if hasattr(h, "SetDirectory"): h.SetDirectory(0)
    return keep(h)

def cut_dir(key, cut):
    return f"{species[key]['top']}/{cut}"

def pid_dir(key, cut, category):
    c = category.replace("pid_", "")
    return f"{cut_dir(key,cut)}/{species[key]['pid_prefix']}_pid_{c}"

def cut_description(key, cut):
    obj = f.Get(f"{cut_dir(key,cut)}/selection")
    return obj.GetTitle() if obj else cut

def safe_name(s):
    return "".join(c if c.isalnum() or c in "_-" else "_" for c in s)

def save_canvas(c, name):
    name = safe_name(name)
    if SAVE_PDF: c.SaveAs(str(OUTDIR/f"{name}.pdf"))
    if SAVE_PNG: c.SaveAs(str(OUTDIR/f"{name}.png"))

def pad_style(pad, right=0.04, grid=False):
    pad.SetLeftMargin(0.13); pad.SetBottomMargin(0.13)
    pad.SetRightMargin(right); pad.SetTopMargin(0.10)
    if grid: pad.SetGrid()

def axis_style(h, x_title=None, y_title=None):
    if x_title is not None: h.GetXaxis().SetTitle(x_title)
    if y_title is not None: h.GetYaxis().SetTitle(y_title)
    for a in (h.GetXaxis(), h.GetYaxis()):
        a.SetTitleSize(0.052); a.SetLabelSize(0.043)
        a.CenterTitle()
    h.GetXaxis().SetTitleOffset(1.00)
    h.GetYaxis().SetTitleOffset(1.12)

def draw_text(lines, x=0.16, y=0.89, size=0.045, dy=0.055):
    t = keep(root.TLatex()); t.SetNDC(); t.SetTextFont(42); t.SetTextSize(size)
    for i, line in enumerate(lines): t.DrawLatex(x, y-i*dy, line)
    return t


# ============================================================
# Plot labels and exact numerical definitions of selected cuts
# ============================================================

CUT_COLORS = [root.kBlack, root.kBlue+1, root.kRed+1, root.kGreen+2]

SIGMA_CUT_TEXT = {
    "cut01_loose": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<40 MeV; |DCA_{p#pi}|<3.0 cm",
        "R_{#Lambda}>1.0 cm; p_{T}^{bach}>0.20 GeV/c; nTPC_{bach}#geq20",
        "|DCA_{xy}^{bach}|<3.0 cm; no #Lambda DIRA requirement",
    ],
    "cut03_baseline": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<25 MeV; |DCA_{p#pi}|<1.5 cm",
        "DIRA_{#Lambda}>0.85; R_{#Lambda}>1.5 cm; p_{T}^{bach}>0.20 GeV/c",
        "nTPC_{bach}#geq25; |DCA_{xy}^{bach}|<2.5 cm",
    ],
    "cut05": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<15 MeV; |DCA_{p#pi}|<0.8 cm",
        "DIRA_{#Lambda}>0.95; R_{#Lambda}>2.0 cm; p_{T}^{bach}>0.25 GeV/c",
        "nTPC_{bach}#geq30; |DCA_{xy}^{bach}|<1.5 cm",
    ],
    "cut08": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<8 MeV; |DCA_{p#pi}|<0.4 cm",
        "DIRA_{#Lambda}>0.99; R_{#Lambda}>3.0 cm; p_{T}^{bach}>0.30 GeV/c",
        "nTPC_{bach}#geq35; |DCA_{xy}^{bach}|<0.7 cm",
    ],
}

CASCADE_CUT_TEXT = {
    "cut02_loose": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<30 MeV; |DCA_{p#pi}|<2.5 cm; p_{T}^{bach}>0.20",
        "nTPC_{bach}#geq20; DCA_{#Lambda,bach}<1.5 cm; R_{cascade}>0.7 cm",
        "DIRA_{cascade}>0.80; L_{#Lambda}^{cascade}>0.3 cm; DIRA_{#Lambda}^{cascade}>0.80;",
    ],
    "cut03_baseline": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<25 MeV; |DCA_{p#pi}|<2.0 cm; p_{T}^{bach}>0.20",
        "nTPC_{bach}#geq25; DCA_{#Lambda,bach}<1.0 cm; R_{cascade}>1.0 cm",
        "DIRA_{cascade}>0.85; L_{#Lambda}^{cascade}>0.5 cm; DIRA_{#Lambda}^{cascade}>0.85;",
    ],
    "cut05": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<20 MeV; |DCA_{p#pi}|<1.0 cm; p_{T}^{bach}>0.25",
        "nTPC_{bach}#geq30; DCA_{#Lambda,bach}<0.6 cm; R_{cascade}>1.5 cm",
        "DIRA_{cascade}>0.93; L_{#Lambda}^{cascade}>1.0 cm; DIRA_{#Lambda}^{cascade}>0.93;",
    ],
    "cut08": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<12 MeV; |DCA_{p#pi}|<0.5 cm; p_{T}^{bach}>0.30",
        "nTPC_{bach}#geq35; DCA_{#Lambda,bach}<0.3 cm; R_{cascade}>2.0 cm",
        "DIRA_{cascade}>0.98; L_{#Lambda}^{cascade}>2.0 cm; DIRA_{#Lambda}^{cascade}>0.98;",
    ],
    "cut09_tight": [
        "|m_{#Lambda}-m_{#Lambda}^{PDG}|<10 MeV; |DCA_{p#pi}|<0.4 cm; p_{T}^{bach}>0.30",
        "nTPC_{bach}#geq35; DCA_{#Lambda,bach}<0.2 cm; R_{cascade}>2.5 cm",
        "DIRA_{cascade}>0.99; L_{#Lambda}^{cascade}>2.0 cm; DIRA_{#Lambda}^{cascade}>0.99;",
    ],
}

def display_cut_name(key, cut):
    try:
        return CUT_DISPLAY_NAMES[SELECTED_CUTS[key].index(cut)]
    except (ValueError, IndexError):
        return cut

def exact_cut_text(key, cut):
    return SIGMA_CUT_TEXT.get(cut, [cut_description(key, cut)]) if key == "sigma" else CASCADE_CUT_TEXT.get(cut, [cut_description(key, cut)])

def topology_qa_without_dca(cfg):
    return [(hname,xtitle) for hname,xtitle in cfg["qa"]
            if "dca" not in hname.lower() and "dca" not in xtitle.lower()]

def draw_cut_tag(key, cut, x=0.16, y=0.90, size=0.040):
    i = SELECTED_CUTS[key].index(cut) if cut in SELECTED_CUTS[key] else 0
    t = keep(root.TLatex())
    t.SetNDC(); t.SetTextFont(62); t.SetTextSize(size)
    t.SetTextColor(CUT_COLORS[i % len(CUT_COLORS)])
    t.DrawLatex(x, y, display_cut_name(key, cut))
    t.SetTextColor(root.kBlack)
    return t

def draw_one_cut_panel(key, cut, extra_lines=None):
    """Information pad for canvases that contain exactly one cut."""
    pad = root.gPad
    pad.Clear(); pad.SetTicks(0,0)
    pad.SetLeftMargin(0.05); pad.SetRightMargin(0.03)
    pad.SetTopMargin(0.04); pad.SetBottomMargin(0.04)

    t = keep(root.TLatex())
    t.SetNDC(); t.SetTextFont(42)
    y = 0.95

    t.SetTextFont(62); t.SetTextSize(0.046)
    t.DrawLatex(0.055, y, species[key]["label"])
    y -= 0.072

    t.SetTextFont(62); t.SetTextSize(0.038)
    t.DrawLatex(0.055, y, "Common selections")
    y -= 0.050
    t.SetTextFont(42); t.SetTextSize(0.029)
    for line in COMMON_SELECTIONS:
        t.DrawLatex(0.075, y, "#bullet  " + line)
        y -= 0.043

    if extra_lines:
        y -= 0.003
        for line in extra_lines:
            t.DrawLatex(0.075, y, line)
            y -= 0.040

    y -= 0.012
    t.SetTextFont(62); t.SetTextSize(0.038)
    t.DrawLatex(0.055, y, "Cut")
    y -= 0.050

    i = SELECTED_CUTS[key].index(cut) if cut in SELECTED_CUTS[key] else 0
    t.SetTextColor(CUT_COLORS[i % len(CUT_COLORS)])
    t.SetTextFont(62); t.SetTextSize(0.034)
    t.DrawLatex(0.075, y, display_cut_name(key, cut))
    y -= 0.047

    t.SetTextColor(root.kBlack); t.SetTextFont(42); t.SetTextSize(0.025)
    for line in exact_cut_text(key, cut):
        t.DrawLatex(0.075, y, line)
        y -= 0.040
    return t

def draw_all_cuts_panel(key, extra_lines=None):
    """Information pad used only by the integrated summary canvas."""
    pad = root.gPad
    pad.Clear(); pad.SetTicks(0,0)
    pad.SetLeftMargin(0.035); pad.SetRightMargin(0.02)
    pad.SetTopMargin(0.025); pad.SetBottomMargin(0.025)

    t = keep(root.TLatex())
    t.SetNDC(); t.SetTextFont(42)
    y = 0.965

    t.SetTextFont(62); t.SetTextSize(0.037)
    t.DrawLatex(0.045, y, species[key]["label"])
    y -= 0.052

    t.SetTextFont(62); t.SetTextSize(0.028)
    t.DrawLatex(0.045, y, "Common selections")
    y -= 0.037
    t.SetTextFont(42); t.SetTextSize(0.020)
    for line in COMMON_SELECTIONS:
        t.DrawLatex(0.060, y, "#bullet  " + line)
        y -= 0.029

    if extra_lines:
        for line in extra_lines:
            t.DrawLatex(0.060, y, line)
            y -= 0.029

    y -= 0.006
    t.SetTextFont(62); t.SetTextSize(0.028)
    t.DrawLatex(0.045, y, "Cut-dependent selections")
    y -= 0.036

    for i,cut in enumerate(SELECTED_CUTS[key][:4]):
        t.SetTextColor(CUT_COLORS[i % len(CUT_COLORS)])
        t.SetTextFont(62); t.SetTextSize(0.023)
        t.DrawLatex(0.055, y, display_cut_name(key, cut))
        y -= 0.029

        t.SetTextColor(root.kBlack); t.SetTextFont(42); t.SetTextSize(0.026)
        for line in exact_cut_text(key, cut):
            t.DrawLatex(0.070, y, line)
            y -= 0.044
        y -= 0.006

    t.SetTextColor(root.kBlack)
    return t

def mass_hist(key, cut):
    cfg = species[key]
    if MASS_PID_CATEGORY is None:
        return get_hist(f"{cut_dir(key,cut)}/{cfg['mass_1d']}")
    return get_hist(f"{pid_dir(key,cut,MASS_PID_CATEGORY)}/h_mass")

def pt_mass_hist(key, cut, ptmin, ptmax):
    cfg = species[key]
    eps = 1.e-7
    if MASS_PID_CATEGORY is None:
        h2 = get_hist(f"{cut_dir(key,cut)}/{cfg['mass_vs_pt']}")
        b1 = h2.GetXaxis().FindBin(ptmin+eps); b2 = h2.GetXaxis().FindBin(ptmax-eps)
        h = h2.ProjectionY(unique(f"h_{key}_{cut}_pt"), b1, b2, "e")
    else:
        h3 = get_hist(f"{pid_dir(key,cut,MASS_PID_CATEGORY)}/h3_mass_vs_pt_vs_signed_lambda_bachelor_dphi")
        b1 = h3.GetYaxis().FindBin(ptmin+eps); b2 = h3.GetYaxis().FindBin(ptmax-eps)
        h = h3.ProjectionX(unique(f"h_{key}_{cut}_pt"), b1, b2, 1, h3.GetNbinsZ(), "e")
    h.SetDirectory(0)
    return keep(h)


In [3]:
# ============================================================
# Check selected folders and print the exact selected cuts
# ============================================================

for key in ("sigma","xi","omega"):
    print(f"\n{key.upper()}")
    for cut in SELECTED_CUTS[key]:
        d = f.GetDirectory(cut_dir(key,cut))
        print(f"  {'OK' if d else 'MISSING':7s} {display_cut_name(key,cut):9s} ({cut})")
        if d:
            for line in exact_cut_text(key,cut):
                print("      ", line)



SIGMA
  OK      Loose     (cut01_loose)
       |m_{#Lambda}-m_{#Lambda}^{PDG}|<40 MeV; |DCA_{p#pi}|<3.0 cm
       R_{#Lambda}>1.0 cm; p_{T}^{bach}>0.20 GeV/c; nTPC_{bach}#geq20
       |DCA_{xy}^{bach}|<3.0 cm; no #Lambda DIRA requirement
  OK      Baseline  (cut03_baseline)
       |m_{#Lambda}-m_{#Lambda}^{PDG}|<25 MeV; |DCA_{p#pi}|<1.5 cm
       DIRA_{#Lambda}>0.85; R_{#Lambda}>1.5 cm; p_{T}^{bach}>0.20 GeV/c
       nTPC_{bach}#geq25; |DCA_{xy}^{bach}|<2.5 cm
  OK      Tight     (cut05)
       |m_{#Lambda}-m_{#Lambda}^{PDG}|<15 MeV; |DCA_{p#pi}|<0.8 cm
       DIRA_{#Lambda}>0.95; R_{#Lambda}>2.0 cm; p_{T}^{bach}>0.25 GeV/c
       nTPC_{bach}#geq30; |DCA_{xy}^{bach}|<1.5 cm
  OK      Tightest  (cut08)
       |m_{#Lambda}-m_{#Lambda}^{PDG}|<8 MeV; |DCA_{p#pi}|<0.4 cm
       DIRA_{#Lambda}>0.99; R_{#Lambda}>3.0 cm; p_{T}^{bach}>0.30 GeV/c
       nTPC_{bach}#geq35; |DCA_{xy}^{bach}|<0.7 cm

XI
  OK      Loose     (cut02_loose)
       |m_{#Lambda}-m_{#Lambda}^{PDG}|<30 MeV; |DCA_{p#pi}|<2

In [4]:
# ============================================================
# 1. Integrated mass summary
#    EXCEPTION: the four selected cuts are compared on one canvas.
#    4 mass pads + 1 pad listing all cuts.
# ============================================================

for key, cfg in species.items():
    c = keep(root.TCanvas(unique(f"c_{key}_mass_summary"), "", 1500, 900))
    c.Divide(3, 2)

    for i,cut in enumerate(SELECTED_CUTS[key][:4]):
        pad = c.cd(i+1); pad_style(pad, grid=True)

        h = mass_hist(key, cut)
        if MASS_REBIN[key] > 1: h.Rebin(MASS_REBIN[key])

        h.SetTitle("")
        axis_style(h, cfg["mass_title"], "candidates")
        h.SetLineColor(CUT_COLORS[i]); h.SetMarkerColor(CUT_COLORS[i])
        h.SetMarkerStyle(20); h.SetMarkerSize(0.65); h.SetLineWidth(2)
        h.SetMinimum(0); h.SetMaximum(1.20*max(h.GetMaximum(),1.))
        h.Draw("E1")
        draw_cut_tag(key, cut, 0.16, 0.91, 0.040)

    c.cd(5)
    draw_all_cuts_panel(key, [DATASET])

    c.cd(6).Clear()
    c.Draw()
    save_canvas(c, f"{key}_mass_selected_cuts")


In [5]:
# ============================================================
# 2. Mass spectra in selected pT intervals
#    One canvas PER CUT.
#    All pT bins stay together on that canvas, plus one cut-info pad.
# ============================================================

for key, cfg in species.items():
    for cut in SELECTED_CUTS[key]:
        bins = PT_BINS[key]
        nplots = len(bins) + 1
        nrows = math.ceil(nplots/N_COLS)

        c = keep(root.TCanvas(unique(f"c_{key}_{cut}_pt"), "", 500*N_COLS, 430*nrows))
        c.Divide(N_COLS, nrows)

        for i,(ptmin,ptmax) in enumerate(bins):
            pad = c.cd(i+1); pad_style(pad, grid=True)

            h = pt_mass_hist(key, cut, ptmin, ptmax)
            if MASS_REBIN[key] > 1: h.Rebin(MASS_REBIN[key])

            h.SetTitle(cfg["label"])
            axis_style(h, cfg["mass_title"], "candidates")
            h.SetLineColor(root.kBlue+2); h.SetMarkerColor(root.kBlue+2)
            h.SetMarkerStyle(20); h.SetMarkerSize(0.75); h.SetLineWidth(2)
            h.SetMinimum(0); h.SetMaximum(1.22*max(h.GetMaximum(),1.))
            h.Draw("E1")
            draw_text([f"{ptmin:g} < p_{{T}} < {ptmax:g} GeV/c"],
                      0.17, 0.84, 0.042, 0.055)

        c.cd(len(bins)+1)
        draw_one_cut_panel(key, cut, [DATASET])

        c.Draw()
        save_canvas(c, f"{key}_{cut}_mass_pt_bins")


In [6]:
# ============================================================
# 3. Topological QA
#    One canvas PER CUT.
#    Do NOT plot DCA QA.
#    All remaining QA variables are on the same canvas in separate pads,
#    plus one pad listing the cut.
# ============================================================

if PLOT_TOPOLOGY_QA:
    for key, cfg in species.items():
        for cut in SELECTED_CUTS[key]:
            qa = topology_qa_without_dca(cfg)
            nplots = len(qa) + 1
            nrows = math.ceil(nplots/N_COLS)

            c = keep(root.TCanvas(unique(f"c_{key}_{cut}_qa"), "", 520*N_COLS, 430*nrows))
            c.Divide(N_COLS, nrows)

            for i,(hname,xtitle) in enumerate(qa):
                pad = c.cd(i+1); pad_style(pad, right=0.14)
                if QA_LOGZ: pad.SetLogz()

                h = get_hist(f"{cut_dir(key,cut)}/{hname}")
                if QA_REBIN_X>1 or QA_REBIN_Y>1:
                    h.Rebin2D(QA_REBIN_X, QA_REBIN_Y)

                h.SetTitle(cfg["label"])
                axis_style(h, xtitle, cfg["mass_title"])
                if QA_MIN_CONTENT is not None: h.SetMinimum(QA_MIN_CONTENT)
                h.Draw("COLZ")

            c.cd(len(qa)+1)
            draw_one_cut_panel(key, cut, [DATASET])

            c.Draw()
            save_canvas(c, f"{key}_{cut}_topology_QA")


In [7]:
# ============================================================
# 4. PID + Lambda-bachelor angular QA
#    One canvas PER CUT, all PID/angular QA in separate pads,
#    plus one pad listing the cut.
# ============================================================

if PLOT_PID_QA:
    for key, cfg in species.items():
        for cut in SELECTED_CUTS[key]:
            nplots = len(pid_qa) + 1
            nrows = math.ceil(nplots/N_COLS)

            c = keep(root.TCanvas(unique(f"c_{key}_{cut}_pidqa"), "", 520*N_COLS, 430*nrows))
            c.Divide(N_COLS, nrows)

            for i,(hname,xtitle) in enumerate(pid_qa):
                pad = c.cd(i+1); pad_style(pad, right=0.14)

                h = get_hist(f"{pid_dir(key,cut,PID_QA_CATEGORY)}/{hname}", required=False)
                if not h:
                    draw_text([f"missing: {hname}"], 0.12, 0.50, 0.035)
                    continue

                if hname.startswith("h_mass_"):
                    if QA_LOGZ: pad.SetLogz()
                    if QA_MIN_CONTENT is not None: h.SetMinimum(QA_MIN_CONTENT)
                    ytitle = cfg["mass_title"]
                else:
                    ytitle = h.GetYaxis().GetTitle()

                if QA_REBIN_X>1 or QA_REBIN_Y>1:
                    h.Rebin2D(QA_REBIN_X, QA_REBIN_Y)

                h.SetTitle(f"{cfg['label']}   PID: {PID_QA_CATEGORY}")
                axis_style(h, xtitle, ytitle)
                h.Draw("COLZ")

            c.cd(len(pid_qa)+1)
            draw_one_cut_panel(key, cut, [DATASET, f"PID QA category: {PID_QA_CATEGORY}"])

            c.Draw()
            save_canvas(c, f"{key}_{cut}_pid_{PID_QA_CATEGORY}_QA")


## Notes

- This version starts from the original uploaded notebook and keeps its input path, selected cuts, \(p_T\) bins, PID settings, rebinning, and ROOT style.
- **Integrated mass summary is the only plot that mixes cuts:** Loose / Baseline / Tight / Tightest are shown in separate pads on one canvas, with a dedicated pad listing all selections.
- **\(p_T\) plots:** one canvas per cut; all selected \(p_T\) intervals remain on that same canvas; the extra pad lists that cut.
- **Topological QA:** one canvas per cut; DCA QA observables are omitted; every other topology QA variable is placed in a different pad on the same canvas; the extra pad lists that cut.
- **PID/angular QA:** one canvas per cut, with a dedicated cut-information pad as well.
- The cut-information pads use the complete numerical definitions of the selected cuts rather than only the abbreviated ROOT `selection` strings.
